# Modelo de difusión de una epidemia con autómatas celulares

**Curso:** Inteligencia Artificial y Minirobots · Universidad Nacional de Colombia

## Objetivo
Representar una población como una cuadrícula y estudiar cómo se propaga una enfermedad usando un autómata celular probabilístico tipo SIR. Cada celda es una persona y solo interactúa con sus ocho vecinos de Moore.

## Estados y reglas
- **S (susceptible):** puede infectarse si tiene vecinos infectados. Con $n$ vecinos infectados, la probabilidad de contagio es $1-(1-\beta)^n$.
- **I (infectado):** se recupera en cada paso con probabilidad $\gamma$.
- **R (recuperado):** permanece recuperado.

Todos los cambios de un paso se calculan a partir de la cuadrícula anterior (actualización sincrónica). Los bordes no se conectan entre sí. La simulación es académica: no modela desplazamientos ni pretende describir una enfermedad real.

Ejecuta las celdas en orden con **Entorno de ejecución > Ejecutar todas**. En Colab, la animación aparece debajo de la última celda.

## 1. ¿Qué es un autómata celular probabilístico?

Un **autómata celular** es un modelo de un sistema compuesto por muchas unidades simples, llamadas celdas. Estas unidades se organizan en una cuadrícula, tienen estados discretos y actualizan su estado en pasos de tiempo usando una regla local. Es **probabilístico** cuando una transición puede ocurrir con una probabilidad, por lo que dos ejecuciones pueden producir resultados distintos.

En este ejercicio, los componentes son:

- **Espacio:** una cuadrícula de 50 filas por 50 columnas; contiene 2.500 celdas.
- **Celda:** representa a una persona. La posición de cada persona permanece fija.
- **Estado:** susceptible (S), infectado (I) o recuperado (R).
- **Vecindad:** las celdas que pueden influir en una persona durante un paso.
- **Regla de transición:** determina cómo puede cambiar el estado de cada persona.
- **Tiempo:** se mide en pasos discretos; cada paso representa una actualización completa de la población, no una duración física específica.

### Vecindad de Moore

Se usa la **vecindad de Moore**: una celda considera las ocho posiciones que la rodean, incluidas las diagonales. La celda central no cuenta como vecina. En los bordes hay menos vecinos; no se conectan los extremos opuestos de la cuadrícula.

```text
N N N
N C N
N N N
```

`C` es la celda actual y cada `N` es una posición vecina. El conteo de infectados entre esas posiciones determina la probabilidad de contagio de una persona susceptible.

### Modelo SIR

El nombre **SIR** resume los tres estados: *Susceptible, Infectado, Recuperado*. En esta versión, la secuencia posible es `S → I → R`: no hay reinfección ni regreso a susceptible. Es una simplificación útil para estudiar propagación espacial y no una descripción clínica completa de una enfermedad.

In [1]:
import importlib.util
import subprocess
import sys

if importlib.util.find_spec('numpy') is None or importlib.util.find_spec('matplotlib') is None:
    subprocess.check_call([sys.executable, '-m', 'pip', 'install', '-q', 'numpy', 'matplotlib'])

import numpy as np
import matplotlib.pyplot as plt
from matplotlib.animation import FuncAnimation
from matplotlib.colors import ListedColormap
from matplotlib.patches import Patch
from IPython.display import HTML, display

plt.rcParams['animation.embed_limit'] = 100
print('Entorno listo')

Entorno listo


## Parámetros

Modifica estos valores para experimentar. La semilla fija hace que la ejecución sea reproducible; usa `None` para obtener una simulación distinta cada vez.

In [2]:
TAMANO_GRID = 50
PROB_CONTAGIO = 0.2
PROB_RECUPERACION = 0.05
INFECTADOS_INICIALES = 5
PASOS = 200
SEMILLA = 42

SUSCEPTIBLE = 0
INFECTADO = 1
RECUPERADO = 2

assert TAMANO_GRID > 0
assert 0 <= PROB_CONTAGIO <= 1
assert 0 <= PROB_RECUPERACION <= 1
assert 0 <= INFECTADOS_INICIALES <= TAMANO_GRID**2
print(f'Población: {TAMANO_GRID**2:,} personas | pasos: {PASOS}')

Población: 2,500 personas | pasos: 200


## Construcción y actualización del autómata

El conteo de vecinos usa relleno con ceros en los bordes y suma los ocho desplazamientos alrededor de cada celda. La actualización es vectorizada con NumPy, pero conserva la regla sincrónica del modelo.

In [3]:
def crear_poblacion(rng):
    poblacion = np.full((TAMANO_GRID, TAMANO_GRID), SUSCEPTIBLE, dtype=np.uint8)
    posiciones = rng.choice(TAMANO_GRID**2, INFECTADOS_INICIALES, replace=False)
    poblacion.flat[posiciones] = INFECTADO
    return poblacion


def contar_vecinos_infectados(poblacion):
    infectados = (poblacion == INFECTADO).astype(np.uint8)
    acolchada = np.pad(infectados, 1, mode='constant')
    cantidad = np.zeros(poblacion.shape, dtype=np.uint8)
    filas, columnas = poblacion.shape
    for desplazamiento_fila in range(3):
        for desplazamiento_columna in range(3):
            if desplazamiento_fila == 1 and desplazamiento_columna == 1:
                continue
            cantidad += acolchada[desplazamiento_fila:desplazamiento_fila + filas,
                                  desplazamiento_columna:desplazamiento_columna + columnas]
    return cantidad


def actualizar(poblacion, rng):
    vecinos_infectados = contar_vecinos_infectados(poblacion)
    probabilidad_contagio = 1 - (1 - PROB_CONTAGIO) ** vecinos_infectados
    aleatorios = rng.random(poblacion.shape)

    nueva_poblacion = poblacion.copy()
    susceptibles = poblacion == SUSCEPTIBLE
    infectados = poblacion == INFECTADO
    se_infectan = susceptibles & (aleatorios < probabilidad_contagio)
    se_recuperan = infectados & (aleatorios < PROB_RECUPERACION)
    nueva_poblacion[se_infectan] = INFECTADO
    nueva_poblacion[se_recuperan] = RECUPERADO
    return nueva_poblacion


def contar_estados(poblacion):
    return np.array([
        np.count_nonzero(poblacion == SUSCEPTIBLE),
        np.count_nonzero(poblacion == INFECTADO),
        np.count_nonzero(poblacion == RECUPERADO),
    ])

## Ejecución y comprobaciones

Se guarda el estado de la cuadrícula y el conteo de cada grupo en todos los pasos para poder animar el resultado. Las comprobaciones confirman que no cambia el tamaño de la población y que el total recuperado nunca disminuye.

In [4]:
rng = np.random.default_rng(SEMILLA)
poblacion = crear_poblacion(rng)
historial = [poblacion.copy()]
conteos = [contar_estados(poblacion)]

for _ in range(PASOS):
    poblacion = actualizar(poblacion, rng)
    historial.append(poblacion.copy())
    conteos.append(contar_estados(poblacion))

historial = np.stack(historial)
conteos = np.stack(conteos)
assert np.all(conteos.sum(axis=1) == TAMANO_GRID**2)
assert np.all(np.diff(conteos[:, RECUPERADO]) >= 0)
assert set(np.unique(historial)).issubset({SUSCEPTIBLE, INFECTADO, RECUPERADO})
print(f'Comprobaciones correctas: {PASOS + 1} estados guardados; población constante de {TAMANO_GRID**2} personas.')
print(f'Estado final (S, I, R): {conteos[-1].tolist()}')

Comprobaciones correctas: 201 estados guardados; población constante de 2500 personas.
Estado final (S, I, R): [0, 0, 2500]


## Visualización

La cuadrícula muestra la distribución espacial y la gráfica de la derecha resume la evolución de susceptibles, infectados y recuperados. La animación incluye el estado inicial y los 200 pasos siguientes.

In [5]:
colores = ListedColormap(['#2878B5', '#E45756', '#54A24B'])
nombres = ['Susceptibles', 'Infectados', 'Recuperados']
pasos = np.arange(PASOS + 1)

fig, (ax_grid, ax_stats) = plt.subplots(1, 2, figsize=(12, 5))
imagen = ax_grid.imshow(historial[0], cmap=colores, vmin=0, vmax=2, interpolation='nearest')
ax_grid.set_title('Difusión de la enfermedad')
ax_grid.set_xlabel('Columna')
ax_grid.set_ylabel('Fila')
ax_grid.legend(handles=[Patch(color=colores(i), label=nombre) for i, nombre in enumerate(nombres)],
               loc='upper center', bbox_to_anchor=(0.5, -0.12), ncol=1, frameon=False)

for indice, nombre in enumerate(nombres):
    ax_stats.plot(pasos, conteos[:, indice], label=nombre, color=colores(indice))
ax_stats.set_xlim(0, PASOS)
ax_stats.set_ylim(0, TAMANO_GRID**2)
ax_stats.set_xlabel('Paso de tiempo')
ax_stats.set_ylabel('Cantidad de personas')
ax_stats.set_title('Evolución de la población')
ax_stats.legend()
ax_stats.grid(alpha=0.25)

def animar(paso):
    imagen.set_data(historial[paso])
    ax_grid.set_title(f'Difusión de la enfermedad · paso {paso}')
    return (imagen,)

animacion = FuncAnimation(fig, animar, frames=PASOS + 1, interval=100, blit=False)
plt.tight_layout()
plt.close(fig)
display(HTML(animacion.to_jshtml()))